Create Folders 

In [0]:
volume_path = "/Volumes/25280065-PA2/volumns/temp"
folders = [
    "flight_landing_zone",
    "flight_landing_zone_part2",
    "cdc_zone_part2",
    "flight_reference_data",
    "checkpoints",
    "schemas"
]
for folder in folders:
    dbutils.fs.mkdirs(f"{volume_path}/{folder}")

In [0]:
from pyspark.sql.types import IntegerType, StringType
from pyspark.sql.functions import col, when, concat_ws, array_sort, concat, lit,current_timestamp, date_format ,array ,window ,avg ,round , sum as _sum , max as _max ,max_by

In [0]:
# insert sample data 
dbutils.fs.cp(
    "dbfs:/databricks-datasets/flights/departuredelays.csv",
    "/Volumes/25280065-PA2/volumns/temp/flight_landing_zone/departuredelays.csv"
)

True

# PART 1: Stream Analytics

## Task 1: Scalable Ingestion with Auto Loader (Bronze Layer)

In [0]:
# Set Paths
catalog = "25280065-PA2"
landing_path = f"{volume_path}/flight_landing_zone"
checkpoint_path = f"{volume_path}/checkpoints/bronze_task1"
schema_path = f"{volume_path}/schemas/bronze_task1"

# Read Stream (Auto Loader)
bronze_df = (
    spark.readStream
    .format("cloudFiles")
    .option("cloudFiles.format", "csv")
    .option("header", "true")
    .option("cloudFiles.schemaLocation", schema_path)
    .option("cloudFiles.schemaEvolutionMode", "rescue")
    .load(landing_path)
)
#Add ingestion_timestamp
bronze_df = bronze_df.withColumn(
    "ingestion_timestamp",
    date_format(current_timestamp(), "yyyy-MM-dd HH:mm:ss")
)
#Write to Bronze Table
bronze_df.writeStream \
    .format("delta") \
    .outputMode("append") \
    .option("checkpointLocation", checkpoint_path) \
    .trigger(availableNow=True) \
    .table(f"`{catalog}`.bronze.flights")


In [0]:
display(spark.read.table("`25280065-PA2`.bronze.flights"))

date,delay,distance,origin,destination,_rescued_data,ingestion_timestamp
01011245,6,602,ABE,ATL,null,2026-03-25 17:28:16
01020600,-8,369,ABE,DTW,null,2026-03-25 17:28:16
01021245,-2,602,ABE,ATL,null,2026-03-25 17:28:16
01020605,-4,602,ABE,ATL,null,2026-03-25 17:28:16
01031245,-4,602,ABE,ATL,null,2026-03-25 17:28:16
01030605,0,602,ABE,ATL,null,2026-03-25 17:28:16
01041243,10,602,ABE,ATL,null,2026-03-25 17:28:16
01040605,28,602,ABE,ATL,null,2026-03-25 17:28:16
01051245,88,602,ABE,ATL,null,2026-03-25 17:28:16
01050605,9,602,ABE,ATL,null,2026-03-25 17:28:16


## Questions:

1. Schema Evolution Mode

schemaEvolutionMode is used to handle changes in the structure of incoming data during streaming. In real-world scenarios, new columns may appear in the data over time. If not handled properly, this can cause the stream to fail.

When schemaEvolutionMode is set to "rescue", any unexpected or new columns are not discarded or cause errors. Instead, they are stored safely in a special column called _rescued_data. This ensures that the pipeline continues to run smoothly without interruption.

This mode should be used when working with dynamic or evolving datasets where the schema is not strictly fixed.

2. Trigger Modes in Streaming

Trigger modes define how and when streaming data is processed in Spark Structured Streaming.

 - availableNow: This mode processes all available data at once and then stops automatically.It is useful for batch-like processing of streaming data, especially in assignments or one-time data ingestion tasks.
 - processingTime: This mode runs the stream continuously and processes data at fixed time intervals (e.g., every 5 seconds). It is commonly used for real-time data processing.
 - once: This mode processes only one micro-batch of data and then stops. It is less commonly used and mainly suitable for specific controlled scenarios.

Each trigger mode is chosen based on the use case, whether it requires continuous real-time processing or one-time batch-style execution.

## Task 2: Data Cleansing, Enrichment, and Standardization (Silver Layer)

In [0]:
bronze_df = spark.readStream.table("`25280065-PA2`.bronze.flights")
#Data Cleaning + Standardization
silver_df = (
    bronze_df
    .withColumn("delay", col("delay").cast(IntegerType()))
    .withColumn("distance", col("distance").cast(IntegerType()))
    .withColumn("origin", col("origin").cast(StringType()))
    .withColumn("destination", col("destination").cast(StringType()))
    .withColumn(
        "event_timestamp",
        to_timestamp(
            concat(lit("2025"), col("date")),
            "yyyyMMddHHmm"
        )
    )
)
# Write to Silver Table
silver_df.writeStream \
    .format("delta") \
    .outputMode("append") \
    .option("checkpointLocation", "/Volumes/25280065-PA2/volumns/temp/checkpoints/silver_task2_part1") \
    .trigger(availableNow=True) \
    .table("`25280065-PA2`.silver.flights_cleaned")


In [0]:
df = spark.read.table("`25280065-PA2`.silver.flights_cleaned")
df.printSchema()
display(df)

root
 |-- date: string (nullable = true)
 |-- delay: integer (nullable = true)
 |-- distance: integer (nullable = true)
 |-- origin: string (nullable = true)
 |-- destination: string (nullable = true)
 |-- _rescued_data: string (nullable = true)
 |-- ingestion_timestamp: string (nullable = true)
 |-- event_timestamp: timestamp (nullable = true)



date,delay,distance,origin,destination,_rescued_data,ingestion_timestamp,event_timestamp
01011245,6,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-01T12:45:00.000Z
01020600,-8,369,ABE,DTW,null,2026-03-25 15:57:10,2025-01-02T06:00:00.000Z
01021245,-2,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-02T12:45:00.000Z
01020605,-4,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-02T06:05:00.000Z
01031245,-4,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-03T12:45:00.000Z
01030605,0,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-03T06:05:00.000Z
01041243,10,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-04T12:43:00.000Z
01040605,28,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-04T06:05:00.000Z
01051245,88,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-05T12:45:00.000Z
01050605,9,602,ABE,ATL,null,2026-03-25 15:57:10,2025-01-05T06:05:00.000Z


# Part 2: Referential Enrichment and Routing Logic

In [0]:
df = spark.read \
    .option("header", "true") \
    .option("delimiter", "\t") \
    .csv("dbfs:/databricks-datasets/flights/airport-codes-na.txt")

display(df)

City,State,Country,IATA
Abbotsford,BC,Canada,YXX
Aberdeen,SD,USA,ABR
Abilene,TX,USA,ABI
Akron,OH,USA,CAK
Alamosa,CO,USA,ALS
Albany,GA,USA,ABY
Albany,NY,USA,ALB
Albuquerque,NM,USA,ABQ
Alexandria,LA,USA,AEX
Allentown,PA,USA,ABE


In [0]:
#Load Reference Data (STATIC)
ref_df = (
    spark.read
    .option("header", "true")
    .option("delimiter", "\t")
    .csv("dbfs:/databricks-datasets/flights/airport-codes-na.txt")
    .select(
        col("IATA").alias("IATA_CODE"),
        col("City").alias("CITY"),
        col("State").alias("STATE")
    )
)
#load data 
silver_stream = spark.readStream.table("`25280065-PA2`.silver.flights_cleaned")
#Join for Departure & Arrival
df = silver_stream.join(
    ref_df.withColumnRenamed("IATA_CODE", "origin_code")
          .withColumnRenamed("CITY", "dep_city")
          .withColumnRenamed("STATE", "dep_state"),
    silver_stream.origin == col("origin_code"),
    "left"
)
df = df.join(
    ref_df.withColumnRenamed("IATA_CODE", "dest_code")
          .withColumnRenamed("CITY", "arr_city")
          .withColumnRenamed("STATE", "arr_state"),
    df.destination == col("dest_code"),
    "left"
)
#Create Required Columns
final_df = (
    df
    .withColumn("departure", concat_ws(", ", col("dep_city"), col("dep_state")))
    .withColumn("arrival", concat_ws(", ", col("arr_city"), col("arr_state")))
    .filter(col("departure").isNotNull() & col("arrival").isNotNull())
    .withColumn(
        "take_off_status",
        when(col("delay") < 0, "Early")
        .when((col("delay") >= 0) & (col("delay") < 10), "On Time")
        .when((col("delay") >= 10) & (col("delay") < 30), "Late")
        .otherwise("Delay")
    )
    .withColumn(
        "standardized_route",
        concat_ws("-", array_sort(array(col("origin"), col("destination"))))
    )
    .withColumn("seq", lit(3))
)
#Select FINAL REQUIRED ORDER
final_df = final_df.select(
    "date",
    "departure",
    "arrival",
    "standardized_route",
    "distance",
    "delay",
    "take_off_status",
    "ingestion_timestamp",
    "event_timestamp",
    "seq"
)
final_df.writeStream \
    .format("delta") \
    .outputMode("append") \
    .option("checkpointLocation", "/Volumes/25280065-PA2/volumns/temp/checkpoints/silver_task2_part2") \
    .trigger(availableNow=True) \
    .table("`25280065-PA2`.silver.flights")


In [0]:
display(spark.read.table("`25280065-PA2`.silver.flights"))

date,departure,arrival,standardized_route,distance,delay,take_off_status,ingestion_timestamp,event_timestamp,seq
01011245,"Allentown, PA","Atlanta, GA",ABE-ATL,602,6,On Time,2026-03-25 15:57:10,2025-01-01T12:45:00.000Z,3
01020600,"Allentown, PA","Detroit, MI",ABE-DTW,369,-8,Early,2026-03-25 15:57:10,2025-01-02T06:00:00.000Z,3
01021245,"Allentown, PA","Atlanta, GA",ABE-ATL,602,-2,Early,2026-03-25 15:57:10,2025-01-02T12:45:00.000Z,3
01020605,"Allentown, PA","Atlanta, GA",ABE-ATL,602,-4,Early,2026-03-25 15:57:10,2025-01-02T06:05:00.000Z,3
01031245,"Allentown, PA","Atlanta, GA",ABE-ATL,602,-4,Early,2026-03-25 15:57:10,2025-01-03T12:45:00.000Z,3
01030605,"Allentown, PA","Atlanta, GA",ABE-ATL,602,0,On Time,2026-03-25 15:57:10,2025-01-03T06:05:00.000Z,3
01041243,"Allentown, PA","Atlanta, GA",ABE-ATL,602,10,Late,2026-03-25 15:57:10,2025-01-04T12:43:00.000Z,3
01040605,"Allentown, PA","Atlanta, GA",ABE-ATL,602,28,Late,2026-03-25 15:57:10,2025-01-04T06:05:00.000Z,3
01051245,"Allentown, PA","Atlanta, GA",ABE-ATL,602,88,Delay,2026-03-25 15:57:10,2025-01-05T12:45:00.000Z,3
01050605,"Allentown, PA","Atlanta, GA",ABE-ATL,602,9,On Time,2026-03-25 15:57:10,2025-01-05T06:05:00.000Z,3


Question 

Broadcast Join and Performance Optimization

A broadcast join improves performance by sending a small dataset (usually a lookup or reference table) to all worker nodes in the cluster. Instead of shuffling large amounts of data across the network, each node already has a local copy of the smaller dataset.

This eliminates the need for expensive data shuffling, which is one of the most costly operations in distributed systems like Spark. As a result, the join operation becomes significantly faster and more efficient.

Broadcast joins are especially useful when one dataset is small enough to fit in memory, such as reference or dimension tables.

## Task 3: Stateful Streaming Aggregations (Gold Layer)

In [0]:
silver_stream = spark.readStream.table("`25280065-PA2`.silver.flights")


##Requirement 1 — Average Delay per Month

In [0]:
monthly_delays_df = (
    silver_stream
    .withWatermark("event_timestamp", "30 days")
    .groupBy(window(col("event_timestamp"), "30 days"))
    .agg(
        round(avg(col("delay") / 60.0), 2).alias("moving_avg_delay")
    )
    .select(
        date_format(col("window.start"), "yyyy-MM-dd HH:mm:ss").alias("window_start"),
        date_format(col("window.end"), "yyyy-MM-dd HH:mm:ss").alias("window_end"),
        col("moving_avg_delay")
    )
)

monthly_delays_df.writeStream \
    .format("delta") \
    .outputMode("append") \
    .option("checkpointLocation", f"{volume_path}/checkpoints/gold_monthly_delays") \
    .trigger(availableNow=True) \
    .table("`25280065-PA2`.gold.monthly_delays")

In [0]:
print("\n===== GOLD MONTHLY DELAYS =====")

df = spark.read.table("`25280065-PA2`.gold.monthly_delays")

print("Total Rows:", df.count())

df.show(10, False)


===== GOLD MONTHLY DELAYS =====
Total Rows: 2
+-------------------+-------------------+----------------+
|window_start       |window_end         |moving_avg_delay|
+-------------------+-------------------+----------------+
|2025-01-12 00:00:00|2025-02-11 00:00:00|0.17            |
|2024-12-13 00:00:00|2025-01-12 00:00:00|0.44            |
+-------------------+-------------------+----------------+



## Requirement 2 — Total Route Distance Every 2 Weeks


In [0]:
biweekly_distance_df = (
    silver_stream
    .withWatermark("event_timestamp", "14 days")
    .groupBy(window(col("event_timestamp"), "14 days"))
    .agg(
        round(_sum("distance"), 0).alias("total_distance")
    )
    .select(
        date_format(col("window.start"), "yyyy-MM-dd HH:mm:ss").alias("window_start"),
        date_format(col("window.end"), "yyyy-MM-dd HH:mm:ss").alias("window_end"),
        col("total_distance")
    )
)

biweekly_distance_df.writeStream \
    .format("delta") \
    .outputMode("append") \
    .option("checkpointLocation", f"{volume_path}/checkpoints/gold_biweekly_distance") \
    .trigger(availableNow=True) \
    .table("`25280065-PA2`.gold.biweekly_distance")

In [0]:
print("\n===== GOLD BIWEEKLY DISTANCE =====")

df = spark.read.table("`25280065-PA2`.gold.biweekly_distance")

print("Total Rows:", df.count())

df.show(10, False)


===== GOLD BIWEEKLY DISTANCE =====
Total Rows: 6
+-------------------+-------------------+--------------+
|window_start       |window_end         |total_distance|
+-------------------+-------------------+--------------+
|2025-01-16 00:00:00|2025-01-30 00:00:00|282509406     |
|2024-12-19 00:00:00|2025-01-02 00:00:00|20636064      |
|2025-01-02 00:00:00|2025-01-16 00:00:00|296623940     |
|2025-02-13 00:00:00|2025-02-27 00:00:00|300210180     |
|2025-01-30 00:00:00|2025-02-13 00:00:00|282459748     |
|2025-02-27 00:00:00|2025-03-13 00:00:00|308990742     |
+-------------------+-------------------+--------------+



## Requirement 3 — Monthly Maximum Delay by Destination

In [0]:
monthly_max_delay_df = (
    silver_stream
    .withWatermark("event_timestamp", "30 days")
    .groupBy(window(col("event_timestamp"), "30 days"))
    .agg(
        max_by(col("standardized_route"), col("delay")).alias("worst_route"),
        round(_max(col("delay") / 60.0), 2).alias("max_delay")
    )
    .select(
        date_format(col("window.start"), "yyyy-MM-dd HH:mm:ss").alias("window_start"),
        date_format(col("window.end"), "yyyy-MM-dd HH:mm:ss").alias("window_end"),
        col("worst_route"),
        col("max_delay")
    )
)

monthly_max_delay_df.writeStream \
    .format("delta") \
    .outputMode("append") \
    .option("checkpointLocation", f"{volume_path}/checkpoints/gold_monthly_max_delay") \
    .trigger(availableNow=True) \
    .table("`25280065-PA2`.gold.monthly_max_delay")

In [0]:
print("\n===== GOLD MONTHLY MAX DELAY (AFTER WRITE) =====")

df = spark.read.table("`25280065-PA2`.gold.monthly_max_delay")

print("Total Rows:", df.count())

df.show(10, False)


===== GOLD MONTHLY MAX DELAY (AFTER WRITE) =====
Total Rows: 2
+-------------------+-------------------+-----------+---------+
|window_start       |window_end         |worst_route|max_delay|
+-------------------+-------------------+-----------+---------+
|2025-01-12 00:00:00|2025-02-11 00:00:00|DFW-FLL    |27.27    |
|2024-12-13 00:00:00|2025-01-12 00:00:00|CMH-LAX    |24.35    |
+-------------------+-------------------+-----------+---------+

